In [1]:
import h5py, json, time, os, cv2
import numpy as np
from IPython.display import Video, display

H5_PATH = '/data/fmalmb/DATA/tmp/Testdata.h5'
CAMERA_IDS = ['cam00', 'cam01', 'cam02', 'cam03', 'cam04', 'cam05', 'cam06']
N_FRAMES = 128
FRAME_OFFSET = 0
FRAME_KEYS = [f'{FRAME_OFFSET + i:06d}' for i in range(N_FRAMES)]
SCALE = 1 / 6

with h5py.File(H5_PATH, 'r') as hf:
    ref = cv2.imdecode(hf['rec/cam00/frames/000000/color'][:], cv2.IMREAD_COLOR)
ORIG_H, ORIG_W = ref.shape[:2]
print(f'H5 OK — {ORIG_W}x{ORIG_H}, {N_FRAMES} frames, {len(CAMERA_IDS)} cameras')

H5 OK — 3360x1890, 128 frames, 7 cameras


In [ ]:
from v3.dwpose_extraction import load_dwpose, extract_keypoints, N_BODY

CACHE_JSON = 'dwpose_body_recon_test.json'
CROP_RIGHT = 200  # pixels to remove from right edge before DWPose inference

cache = None
if os.path.exists(CACHE_JSON):
    with open(CACHE_JSON) as f:
        cache = json.load(f)
    if cache.get('_crop_right', 0) != CROP_RIGHT:
        print(f'Cache has crop_right={cache.get("_crop_right",0)}, current={CROP_RIGHT} — re-extracting.')
        cache = None
    else:
        print(f'Loading from cache: {CACHE_JSON}')

if cache is not None:
    keypoints_px   = np.zeros((len(CAMERA_IDS), N_FRAMES, N_BODY, 2), dtype=np.float32)
    keypoints_conf = np.zeros((len(CAMERA_IDS), N_FRAMES, N_BODY),    dtype=np.float32)
    presence       = np.zeros((len(CAMERA_IDS), N_FRAMES),             dtype=bool)
    for ci, cam_id in enumerate(CAMERA_IDS):
        for fi, fk in enumerate(FRAME_KEYS):
            entry = cache.get(cam_id, {}).get(fk, {})
            if entry.get('detected', False):
                keypoints_px[ci, fi]   = np.array(entry['keypoints'], dtype=np.float32)
                keypoints_conf[ci, fi] = np.array(entry['confidence'], dtype=np.float32)
                presence[ci, fi]       = True
    print('Done.')
else:
    print(f'Running DWPose inference (crop_right={CROP_RIGHT})...')
    session_det, session_pose = load_dwpose(use_gpu=True)
    keypoints_px, keypoints_conf, presence = extract_keypoints(
        H5_PATH, CAMERA_IDS, FRAME_KEYS, session_det, session_pose,
        verbose=True, crop_right=CROP_RIGHT,
    )
    cache = {'_crop_right': CROP_RIGHT}
    for ci, cam_id in enumerate(CAMERA_IDS):
        cache[cam_id] = {}
        for fi, fk in enumerate(FRAME_KEYS):
            if presence[ci, fi]:
                cache[cam_id][fk] = {
                    'detected':   True,
                    'keypoints':  keypoints_px[ci, fi].tolist(),
                    'confidence': keypoints_conf[ci, fi].tolist(),
                }
            else:
                cache[cam_id][fk] = {'detected': False}
    with open(CACHE_JSON, 'w') as f:
        json.dump(cache, f)
    print(f'Saved cache to {CACHE_JSON}')

for ci, cam_id in enumerate(CAMERA_IDS):
    print(f'  {cam_id}: {int(presence[ci].sum())}/{N_FRAMES} detected')

In [3]:
from v3.skeletons import DWPOSE_BODY_CONNECTIONS

DW_JOINT_NAMES = [
    'nose', 'neck', 'r_shoulder', 'r_elbow', 'r_wrist',
    'l_shoulder', 'l_elbow', 'l_wrist',
    'r_hip', 'r_knee', 'r_ankle',
    'l_hip', 'l_knee', 'l_ankle',
    'r_eye', 'l_eye', 'r_ear', 'l_ear',
]
_RIGHT_IDX = {2, 3, 4, 8, 9, 10, 14, 16}
_LEFT_IDX  = {5, 6, 7, 11, 12, 13, 15, 17}
_C_LEFT    = (50, 200, 50)
_C_RIGHT   = (50, 50, 220)
_C_CENTER  = (50, 210, 210)
_C_LINE    = (180, 180, 180)

def _jc(i):
    return _C_LEFT if i in _LEFT_IDX else (_C_RIGHT if i in _RIGHT_IDX else _C_CENTER)

SCORE_THRESH = 0.1
FONT = cv2.FONT_HERSHEY_SIMPLEX
DOT_R = 5

def draw_joints_labeled(cell_img, pts_cell, scores_cell):
    for a, b in DWPOSE_BODY_CONNECTIONS:
        if a in pts_cell and b in pts_cell:
            cv2.line(cell_img, pts_cell[a], pts_cell[b], _C_LINE, 1, cv2.LINE_AA)
    for i, (cx, cy) in pts_cell.items():
        color = _jc(i)
        cv2.circle(cell_img, (cx, cy), DOT_R, color, -1, cv2.LINE_AA)
        cv2.circle(cell_img, (cx, cy), DOT_R, (255, 255, 255), 1, cv2.LINE_AA)
        label = f'{i}: {scores_cell[i]:.2f}'
        ox, oy = cx + DOT_R + 2, cy - 2
        (tw, th), _ = cv2.getTextSize(label, FONT, 0.32, 1)
        cv2.rectangle(cell_img, (ox - 1, oy - th - 1), (ox + tw + 1, oy + 2), (10, 10, 10), -1)
        cv2.putText(cell_img, label, (ox, oy), FONT, 0.32, color, 1, cv2.LINE_AA)

def draw_legend(cell_img):
    cell_img[:] = (15, 15, 15)
    cell_h, cell_w = cell_img.shape[:2]
    title = 'DWPose OpenPose-18'
    (tw, th), _ = cv2.getTextSize(title, FONT, 0.43, 1)
    cv2.putText(cell_img, title, ((cell_w - tw) // 2, th + 8), FONT, 0.43, (200, 200, 200), 1, cv2.LINE_AA)
    for i, name in enumerate(DW_JOINT_NAMES):
        y = th + 28 + i * 18
        if y + 18 > cell_h:
            break
        cv2.putText(cell_img, f'{i:2d}: {name}', (12, y), FONT, 0.38, _jc(i), 1, cv2.LINE_AA)

OUT_LABELED = 'dwpose_labeled_preview.mp4'
GRID_COLS, GRID_ROWS = 4, 2
cell_w = int(round(ORIG_W * SCALE)); cell_w += cell_w % 2
cell_h = int(round(ORIG_H * SCALE)); cell_h += cell_h % 2
sx, sy = cell_w / ORIG_W, cell_h / ORIG_H

writer = cv2.VideoWriter(OUT_LABELED, cv2.VideoWriter_fourcc(*'mp4v'), 15.0, (GRID_COLS * cell_w, GRID_ROWS * cell_h))
with h5py.File(H5_PATH, 'r') as hf:
    for fi, fk in enumerate(FRAME_KEYS):
        grid = np.zeros((GRID_ROWS * cell_h, GRID_COLS * cell_w, 3), dtype=np.uint8)
        for ci, cam_id in enumerate(CAMERA_IDS):
            img = cv2.imdecode(hf[f'rec/{cam_id}/frames/{fk}/color'][:], cv2.IMREAD_COLOR)
            cell = cv2.resize(img, (cell_w, cell_h), interpolation=cv2.INTER_AREA)
            if presence[ci, fi]:
                kps = keypoints_px[ci, fi]; scores = keypoints_conf[ci, fi]
                pts = {j: (int(round(float(np.clip(kps[j, 0] * sx, 0, cell_w - 1)))),
                           int(round(float(np.clip(kps[j, 1] * sy, 0, cell_h - 1)))))
                       for j in range(N_BODY) if scores[j] >= SCORE_THRESH}
                draw_joints_labeled(cell, pts, scores)
            row, col = divmod(ci, GRID_COLS)
            grid[row * cell_h:(row + 1) * cell_h, col * cell_w:(col + 1) * cell_w] = cell
        legend = np.zeros((cell_h, cell_w, 3), dtype=np.uint8)
        draw_legend(legend)
        grid[cell_h:2 * cell_h, 3 * cell_w:4 * cell_w] = legend
        writer.write(grid)
writer.release()
print(f'Wrote {OUT_LABELED}')
display(Video(OUT_LABELED, embed=True))

Wrote dwpose_labeled_preview.mp4


In [4]:
from v3.calibration import load_calibration
from v3.triangulation import undistort_keypoints

CAMERA_CALIB, CAMERA_WORLD_TRANSFORMS, PROJECTION_MATRICES, _ = load_calibration(H5_PATH)

keypoints_px_undist = undistort_keypoints(keypoints_px, CAMERA_CALIB, CAMERA_IDS)

OUT_UNDIST = 'dwpose_undistorted_preview.mp4'
writer = cv2.VideoWriter(OUT_UNDIST, cv2.VideoWriter_fourcc(*'mp4v'), 15.0, (GRID_COLS * cell_w, GRID_ROWS * cell_h))
with h5py.File(H5_PATH, 'r') as hf:
    for fi, fk in enumerate(FRAME_KEYS):
        grid = np.zeros((GRID_ROWS * cell_h, GRID_COLS * cell_w, 3), dtype=np.uint8)
        for ci, cam_id in enumerate(CAMERA_IDS):
            img = cv2.imdecode(hf[f'rec/{cam_id}/frames/{fk}/color'][:], cv2.IMREAD_COLOR)
            cal  = CAMERA_CALIB[cam_id]
            img_ud = cv2.undistort(img, cal['K'], cal['dist'])
            cell = cv2.resize(img_ud, (cell_w, cell_h), interpolation=cv2.INTER_AREA)
            if presence[ci, fi]:
                kps    = keypoints_px_undist[ci, fi]
                scores = keypoints_conf[ci, fi]
                pts = {j: (int(round(float(np.clip(kps[j, 0] * sx, 0, cell_w - 1)))),
                           int(round(float(np.clip(kps[j, 1] * sy, 0, cell_h - 1)))))
                       for j in range(N_BODY) if scores[j] >= SCORE_THRESH}
                draw_joints_labeled(cell, pts, scores)
            row, col = divmod(ci, GRID_COLS)
            grid[row * cell_h:(row + 1) * cell_h, col * cell_w:(col + 1) * cell_w] = cell
        legend = np.zeros((cell_h, cell_w, 3), dtype=np.uint8)
        draw_legend(legend)
        grid[cell_h:2 * cell_h, 3 * cell_w:4 * cell_w] = legend
        writer.write(grid)
writer.release()
print(f'Wrote {OUT_UNDIST}')
display(Video(OUT_UNDIST, embed=True))

  cam00: fx=2014.5, fy=2014.5, cx=1673.0, cy=918.5
  cam01: fx=1997.1, fy=1997.1, cx=1690.5, cy=956.0
  cam02: fx=1990.6, fy=1990.6, cx=1723.1, cy=937.1
  cam03: fx=2011.3, fy=2011.3, cx=1700.2, cy=926.9
  cam04: fx=1995.0, fy=1995.0, cx=1697.7, cy=953.3
  cam05: fx=2014.8, fy=2014.8, cx=1728.1, cy=950.2
  cam06: fx=2002.5, fy=2002.5, cx=1679.1, cy=964.0
Loaded ChameleonCalibrationV1 (7 cameras, gravity=[0. 1. 0.])
7 cameras: ['cam00', 'cam01', 'cam02', 'cam03', 'cam04', 'cam05', 'cam06']
Wrote dwpose_undistorted_preview.mp4


In [7]:
from v3.triangulation import ransac_triangulate_sequence
from v3.smoothing import smooth_sequence, jitter_flags, savgol_and_upsample_2x

SEED_JOINT = (8, 11)   # hip midpoint
REPROJ_THRESH = 100.0

result = ransac_triangulate_sequence(
    keypoints_px_undist, keypoints_conf, presence, PROJECTION_MATRICES, CAMERA_IDS,
    seed_joint_idx=SEED_JOINT,
    occlusion=None,
    reproj_thresh_px=REPROJ_THRESH,
)
joints3d          = result['joints3d']
valid             = result['valid']
n_inliers         = result['n_inliers']
reproj_err        = result['reproj_err']
seed_residuals    = result['seed_residuals']
hysteresis_overrides = result['hysteresis_overrides']
n_valid_frames    = result['n_valid_frames']

n_valid = int(valid.sum())
ni = n_inliers[valid]
print(f'RANSAC (hip-midpoint seed):')
print(f'  {n_valid}/{N_FRAMES} frames valid')
print(f'  inlier cams: min={ni.min()}, mean={ni.mean():.2f}, max={ni.max()}')
print(f'  mean reproj error: {np.nanmean(reproj_err[valid]):.1f}px')
print(f'  hysteresis overrides: {int(hysteresis_overrides)}/{int(n_valid_frames)} valid frames')
print(f'  hip-midpoint seed residual (px): mean={seed_residuals.mean():.1f}, '
      f'median={np.median(seed_residuals):.1f}, max={seed_residuals.max():.1f}')

# ---- Kalman/RTS smooth
joints3d_smooth, valid_smooth = smooth_sequence(
    joints3d, valid, n_inliers,
    process_std=0.03, meas_std_base=0.01, meas_std_2cam=0.015, min_inliers_base=3,
)
HIP_MID_SEED = np.array(SEED_JOINT)
hip_raw    = joints3d[:, HIP_MID_SEED].mean(axis=1)
hip_smooth = joints3d_smooth[:, HIP_MID_SEED].mean(axis=1)
delta = np.linalg.norm(hip_raw[valid] - hip_smooth[valid], axis=-1)
print(f'\nKalman hip correction (cm): mean={delta.mean()*100:.2f}, max={delta.max()*100:.2f}')

# ---- Jitter flags
jitter_flag, hip_jitter_res = jitter_flags(
    joints3d, joints3d_smooth, valid, seed_joint_idx=SEED_JOINT, mad_factor=4.0)
valid_idx = np.where(valid)[0]
res = hip_jitter_res[valid_idx]
med = np.median(res); mad = np.median(np.abs(res - med)) + 1e-9
thresh = med + 4.0 * mad
flagged = valid_idx[res > thresh]
print(f'hip jitter (cm): median={med*100:.2f}, mad={mad*100:.2f}, thresh={thresh*100:.2f}, max={res.max()*100:.2f}')
print(f'flagged {len(flagged)}/{len(valid_idx)} frames: {(flagged + FRAME_OFFSET).tolist()}')

# ---- SG + 2x upsample
sg = savgol_and_upsample_2x(joints3d_smooth, valid_smooth, sg_window=7, sg_polyorder=3)
joints3d_sg     = sg['joints3d_sg']
joints3d_2x     = sg['joints3d_2x']
valid_2x        = sg['valid_2x']
N_FRAMES_2X     = sg['n_frames_2x']
nearest_orig_2x = sg['nearest_orig_2x']
jitter_flag_2x  = jitter_flag[nearest_orig_2x]
n_inliers_2x    = n_inliers[nearest_orig_2x]

hip_smooth_v = joints3d_smooth[:, HIP_MID_SEED].mean(axis=1)
hip_sg_v     = joints3d_sg[:, HIP_MID_SEED].mean(axis=1)
delta_sg = np.linalg.norm(hip_smooth_v[valid_smooth] - hip_sg_v[valid_smooth], axis=-1)
print(f'SG correction (cm): mean={delta_sg.mean()*100:.3f}, max={delta_sg.max()*100:.3f}')
print(f'{int(valid_2x.sum())}/{N_FRAMES_2X} frames valid at 2x')

RANSAC (hip-midpoint seed):
  128/128 frames valid
  inlier cams: min=2, mean=3.18, max=4
  mean reproj error: 78.7px
  hysteresis overrides: 0/128 valid frames
  hip-midpoint seed residual (px): mean=54.6, median=43.2, max=86.0

Kalman hip correction (cm): mean=1.27, max=8.68
hip jitter (cm): median=0.25, mad=0.21, thresh=1.10, max=8.68
flagged 44/128 frames: [6, 7, 8, 29, 30, 32, 33, 34, 35, 36, 37, 38, 39, 41, 42, 55, 56, 74, 75, 76, 78, 79, 80, 81, 82, 83, 84, 85, 86, 87, 90, 91, 92, 93, 94, 95, 96, 97, 98, 101, 102, 106, 107, 108]
SG correction (cm): mean=0.675, max=4.279
255/255 frames valid at 2x


In [ ]:
import viser
from v3 import visualization as viz

# Joints/connections to skip (knees + ankles almost never in frame)
_VIS_SKIP = {9, 10, 12, 13}
VIS_JOINTS = [j for j in range(N_BODY) if j not in _VIS_SKIP]
VIS_CONNECTIONS = [(a, b) for a, b in DWPOSE_BODY_CONNECTIONS if a not in _VIS_SKIP and b not in _VIS_SKIP]

ORIGIN_WORLD = viz.compute_origin(joints3d, valid)
DWPOSE_COLOR = np.array([255, 170, 40], dtype=np.uint8)

# Pre-compute viser-space points for all valid 2x frames (all 18 joints stored;
# connections are filtered at render time).
dwpose_pts_2x = {
    fi2x: np.stack([viz.world_to_viser_point(p, ORIGIN_WORLD)
                    for p in joints3d_2x[fi2x]]).astype(np.float32)
    for fi2x in range(N_FRAMES_2X) if valid_2x[fi2x]
}
print(f'Pre-computed {len(dwpose_pts_2x)} 2x skeleton frames.')

server = viser.ViserServer()
running = True
try:
    server.scene.set_up_direction('+z')
    server.gui.configure_theme(dark_mode=True)
    viz.setup_cameras(server, CAMERA_CALIB, CAMERA_WORLD_TRANSFORMS, ORIGIN_WORLD)
    server.initial_camera.position = (2.5, 2.0, 1.6)
    server.initial_camera.look_at  = (0.0, 0.0, 0.9)
    server.initial_camera.up       = (0.0, 0.0, 1.0)

    stop_button = server.gui.add_button('Stop viewer')
    with server.gui.add_folder('Playback'):
        frame_slider = server.gui.add_slider('Frame (2x)', min=0, max=N_FRAMES_2X - 1, step=1, initial_value=0)
        play_button  = server.gui.add_button('▶ / ⏸  Play / Pause')
        fps_slider   = server.gui.add_slider('FPS', min=1, max=60, step=1, initial_value=20)

    @stop_button.on_click
    def _stop(_): global running; running = False

    is_playing = [False]
    @play_button.on_click
    def _toggle(_): is_playing[0] = not is_playing[0]

    last_rendered = [-1]
    def _force(_): last_rendered[0] = -1
    frame_slider.on_update(_force)

    _empty_pts  = np.zeros((0, 3), dtype=np.float32)
    _empty_segs = np.zeros((0, 2, 3), dtype=np.float32)
    _empty_col  = np.zeros((0, 3), dtype=np.uint8)

    def render_frame(fi2x):
        if fi2x in dwpose_pts_2x:
            pts  = dwpose_pts_2x[fi2x]
            vis  = pts[VIS_JOINTS]
            segs = np.array([[pts[a], pts[b]] for a, b in VIS_CONNECTIONS], dtype=np.float32)
            server.scene.add_point_cloud('/dwpose/joints', vis,
                colors=np.full((len(VIS_JOINTS), 3), DWPOSE_COLOR, dtype=np.uint8),
                point_size=0.008)
            server.scene.add_line_segments('/dwpose/skeleton', segs,
                colors=DWPOSE_COLOR, line_width=2.0)
        else:
            server.scene.add_point_cloud('/dwpose/joints', _empty_pts, colors=_empty_col)
            server.scene.add_line_segments('/dwpose/skeleton', _empty_segs, colors=_empty_col)

    render_frame(0); last_rendered[0] = 0
    last_advance = time.time()
    print('Viser running — open the URL above. Press Stop to exit.')

    while running:
        fi = frame_slider.value
        if fi != last_rendered[0]:
            render_frame(fi); last_rendered[0] = fi
        if is_playing[0]:
            now = time.time()
            if now - last_advance >= 1.0 / fps_slider.value:
                frame_slider.value = (fi + 1) % N_FRAMES_2X
                last_advance = now
        time.sleep(0.01)

except KeyboardInterrupt:
    print('Interrupted.')
finally:
    server.stop()
    print('Viser stopped.')